# Contours for source–sink pair and uniform flows

A line source of strength $m$ is located at $(-a,0)$ and an equal line sink is located at $(a,0)$. We use the convention

$$u=\frac{\partial\psi}{\partial y}, \qquad v=-\frac{\partial\psi}{\partial x}.$$

With $\theta_s=\operatorname{atan2}(y,x+a)$ and $\theta_k=\operatorname{atan2}(y,x-a)$, the source–sink contribution is

$$\psi_{sk}=m(\theta_s-\theta_k).$$

If the volume flux per unit depth is $Q$, then $Q=2\pi m$ and $m=Q/(2\pi)$. The cases below progress from no uniform flow, to an aligned uniform flow, and finally to an inclined uniform flow.


In [89]:
import numpy as np
import plotly.graph_objects as go
import plotly.io as pio
from IPython.display import HTML, display


def show_plotly(fig, *, config=None):
    """Display Plotly without loading its legacy MathJax integration."""
    plot_config = {"responsive": True}
    if config:
        plot_config.update(config)
    return display(HTML(pio.to_html(
        fig, full_html=False, include_plotlyjs="cdn",
        include_mathjax=False, config=plot_config,
    )))


def add_contours(fig, z, start, end, size, color="#286090", width=1.2, name=None, showlegend=False):
    """Add an unfilled family of Plotly contour lines with a single color."""
    # A half-resolution display grid keeps the interactive page light while
    # preserving the full-resolution arrays used by the calculations.
    display_stride = 2
    z_display = np.ma.filled(z, np.nan)[::display_stride, ::display_stride]
    fig.add_trace(go.Contour(
        x=x[::display_stride], y=y[::display_stride], z=z_display, autocontour=False,
        contours=dict(start=float(start), end=float(end), size=float(size), coloring="lines"),
        colorscale=[[0, color], [1, color]], line=dict(width=width),
        showscale=False,
        hovertemplate="ψ = %{z:.3f}<br>x = %{x:.3f}<br>y = %{y:.3f}<extra></extra>",
        name=name, showlegend=showlegend,
        connectgaps=False,
    ))


def add_direction_arrows(fig, x_grid, y_grid, u_grid, v_grid, length=0.28, color="#333333"):
    """Draw normalized velocity arrows as one lightweight Plotly scatter trace."""
    xs, ys = [], []
    u_values = np.ma.filled(u_grid, np.nan)
    v_values = np.ma.filled(v_grid, np.nan)
    for x0, y0, u0, v0 in zip(
        np.ravel(x_grid), np.ravel(y_grid), np.ravel(u_values), np.ravel(v_values)
    ):
        if not np.isfinite(u0) or not np.isfinite(v0):
            continue
        half = 0.5 * length
        tip_x, tip_y = x0 + half * u0, y0 + half * v0
        tail_x, tail_y = x0 - half * u0, y0 - half * v0
        head, wing = 0.30 * length, 0.16 * length
        base_x, base_y = tip_x - head * u0, tip_y - head * v0
        left_x, left_y = base_x - wing * v0, base_y + wing * u0
        right_x, right_y = base_x + wing * v0, base_y - wing * u0
        xs.extend([tail_x, tip_x, None, left_x, tip_x, right_x, None])
        ys.extend([tail_y, tip_y, None, left_y, tip_y, right_y, None])
    fig.add_trace(go.Scatter(
        x=xs, y=ys, mode="lines", line=dict(color=color, width=1.2),
        hoverinfo="skip", showlegend=False, name="Flow direction",
    ))


def add_point(fig, x_value, y_value, name, color, symbol="circle", size=12, showlegend=True):
    fig.add_trace(go.Scatter(
        x=[x_value], y=[y_value], mode="markers", name=name, showlegend=showlegend,
        marker=dict(symbol=symbol, size=size, color=color, line=dict(color="black", width=1)),
    ))


def style_flow_figure(fig, title):
    fig.update_layout(
        title=title, autosize=True, height=675, template="plotly_white", hovermode="closest",
        legend=dict(x=0.99, y=0.99, xanchor="right", yanchor="top",
                    bgcolor="rgba(255,255,255,0.94)", bordercolor="#777777", borderwidth=1),
        margin=dict(l=65, r=30, t=75, b=60),
    )
    fig.update_xaxes(title_text="x", range=[-4, 4], gridcolor="#dddddd",
                     zeroline=True, zerolinecolor="#999999", constrain="domain")
    fig.update_yaxes(title_text="y", range=[-3, 3], gridcolor="#dddddd",
                     zeroline=True, zerolinecolor="#999999", scaleanchor="x", scaleratio=1)


## Parameters and numerical grid

In [90]:
a = 1.0
m = 1.0
U = 1.0
Q = 2 * np.pi * m

x = np.linspace(-4.0, 4.0, 701)
y = np.linspace(-3.0, 3.0, 551)
X, Y = np.meshgrid(x, y)

theta_source = np.arctan2(Y, X + a)
theta_sink = np.arctan2(Y, X - a)
r_source_sq = (X + a)**2 + Y**2
r_sink_sq = (X - a)**2 + Y**2
singularity_mask = (r_source_sq < 0.08**2) | (r_sink_sq < 0.08**2)

# Prevent contour interpolation across the atan2 branch cut.
dy = y[1] - y[0]
branch_cut_mask = (np.abs(Y) <= 1.1 * dy) & (X > -a) & (X < a)

print(f"Q = {Q:.4f}")


Q = 6.2832


## Source–sink pair without a uniform flow

First set $U=0$ while retaining $a=1$ and $m=1$. The streamfunction becomes

$$\boxed{\psi(x,y)=m\left[\operatorname{atan2}(y,x+a)-\operatorname{atan2}(y,x-a)\right]}.$$

The velocity components are

$$\begin{aligned}
u&=m\frac{x+a}{(x+a)^2+y^2}-m\frac{x-a}{(x-a)^2+y^2},\\[4pt]
v&=m\frac{y}{(x+a)^2+y^2}-m\frac{y}{(x-a)^2+y^2}.
\end{aligned}$$

The streamlines run from the source to the sink and form circles through the two singularities. Since the complex velocity $-2am/(z^2-a^2)$ has no finite zero, this flow has no finite stagnation points.


In [91]:
psi_pair = m * (theta_source - theta_sink)
psi_pair_plot = np.ma.array(psi_pair, mask=singularity_mask | branch_cut_mask)

with np.errstate(divide="ignore", invalid="ignore"):
    u_pair = m * (X + a) / r_source_sq - m * (X - a) / r_sink_sq
    v_pair = m * Y / r_source_sq - m * Y / r_sink_sq

In [92]:
fig = go.Figure()

negative_pair_levels = np.linspace(-0.95 * np.pi * m, -0.10, 16)
positive_pair_levels = np.linspace(0.10, 0.95 * np.pi * m, 16)
add_contours(fig, psi_pair_plot, negative_pair_levels[0], negative_pair_levels[-1],
             negative_pair_levels[1] - negative_pair_levels[0])
add_contours(fig, psi_pair_plot, positive_pair_levels[0], positive_pair_levels[-1],
             positive_pair_levels[1] - positive_pair_levels[0])

xqp = np.linspace(-3.6, 3.6, 13)
yqp = np.linspace(-2.5, 2.5, 9)
Xqp, Yqp = np.meshgrid(xqp, yqp)
d_source_p = (Xqp + a)**2 + Yqp**2
d_sink_p = (Xqp - a)**2 + Yqp**2
with np.errstate(divide="ignore", invalid="ignore"):
    Uqp = m * (Xqp + a) / d_source_p - m * (Xqp - a) / d_sink_p
    Vqp = m * Yqp / d_source_p - m * Yqp / d_sink_p
    speed_qp = np.hypot(Uqp, Vqp)
    Uqp, Vqp = Uqp / speed_qp, Vqp / speed_qp
near_singularity_p = (d_source_p < 0.16) | (d_sink_p < 0.16)
Uqp = np.ma.array(Uqp, mask=near_singularity_p | ~np.isfinite(Uqp))
Vqp = np.ma.array(Vqp, mask=near_singularity_p | ~np.isfinite(Vqp))
add_direction_arrows(fig, Xqp, Yqp, Uqp, Vqp)

add_point(fig, -a, 0, "Source", "#1565c0")
add_point(fig, a, 0, "Sink", "#01bb1a")
fig.add_annotation(x=-a, y=0, text="<b>Source (−a, 0)</b>", showarrow=True,
                   ax=-70, ay=35, arrowcolor="#1565c0", font=dict(color="#1565c0", size=14, family="Arial Black, Arial, sans-serif"))
fig.add_annotation(x=a, y=0, text="<b>Sink (a, 0)</b>", showarrow=True,
                   ax=65, ay=35, arrowcolor="#01bb1a", font=dict(color="#01bb1a", size=14, family="Arial Black, Arial, sans-serif"))
style_flow_figure(fig, "Streamlines for a source–sink pair without uniform flow (a = m = 1)")
show_plotly(fig)


## Source–sink pair in a uniform flow

Now add a uniform flow of speed $U$ in the positive $x$ direction. Its streamfunction is $Uy$, so

$$\boxed{\psi(x,y)=Uy+m\theta_s-m\theta_k}.$$

Differentiating gives

$$\begin{aligned}
u(x,y)&=U+m\frac{x+a}{(x+a)^2+y^2}-m\frac{x-a}{(x-a)^2+y^2},\\[4pt]
v(x,y)&=m\frac{y}{(x+a)^2+y^2}-m\frac{y}{(x-a)^2+y^2}.
\end{aligned}$$

The two `atan2` angles have a $2\pi$ branch jump on the segment joining the source and sink. That segment is masked only when drawing contours; the velocity field itself is single-valued away from the singularities.


In [93]:
psi = U * Y + m * (theta_source - theta_sink)
psi_plot = np.ma.array(psi, mask=singularity_mask | branch_cut_mask)

with np.errstate(divide="ignore", invalid="ignore"):
    u = U + m * (X + a) / r_source_sq - m * (X - a) / r_sink_sq
    v = m * Y / r_source_sq - m * Y / r_sink_sq


## Stagnation points and the Rankine oval

On the $x$ axis outside the source–sink pair, $v=0$ and

$$u(x,0)=U-\frac{2am}{x^2-a^2}.$$

Therefore the two stagnation points are

$$\boxed{(x,y)=\left(\pm\sqrt{a^2+\frac{2am}{U}},0\right)}.$$

The closed streamline $\psi=0$ that joins these points is the boundary of the **Rankine oval**. The following cell computes its upper half by bisection and reflects it about the $x$ axis.

In [94]:
x_stag = np.sqrt(a**2 + 2 * a * m / U)
stagnation_x = np.array([-x_stag, x_stag])

def streamfunction(x_value, y_value):
    return (
        U * y_value
        + m * np.arctan2(y_value, x_value + a)
        - m * np.arctan2(y_value, x_value - a)
    )

x_oval = np.linspace(-x_stag, x_stag, 601)
y_oval = np.zeros_like(x_oval)

for i, x_value in enumerate(x_oval[1:-1], start=1):
    y_low, y_high = 1e-10, y.max()
    for _ in range(60):
        y_mid = 0.5 * (y_low + y_high)
        if streamfunction(x_value, y_mid) > 0:
            y_high = y_mid
        else:
            y_low = y_mid
    y_oval[i] = 0.5 * (y_low + y_high)

print(f"Stagnation points: ({-x_stag:.4f}, 0) and ({x_stag:.4f}, 0)")

Stagnation points: (-1.7321, 0) and (1.7321, 0)


## Constructing the final flow picture

The figure is built in three steps. Streamlines are retained both outside and inside the Rankine oval; the interior curves run from the source to the sink.
Hover over any contour to see its constant streamfunction value $\psi$ and the cursor coordinates.

### Step 1 — Draw the streamlines

In [95]:
levels = np.r_[np.linspace(-3.0, -0.15, 15), np.linspace(0.15, 3.0, 15)]
fig = go.Figure()
add_contours(fig, psi_plot, levels[0], levels[14], levels[1] - levels[0])
add_contours(fig, psi_plot, levels[15], levels[-1], levels[16] - levels[15])
style_flow_figure(fig, "Step 1: streamlines ψ = constant")
show_plotly(fig)


### Step 2 — Add the Rankine oval and characteristic points

The red curve is the closed $\psi=0$ streamline. The stars mark the two stagnation points.

In [96]:
fig = go.Figure()
add_contours(fig, psi_plot, levels[0], levels[14], levels[1] - levels[0])
add_contours(fig, psi_plot, levels[15], levels[-1], levels[16] - levels[15])

oval_color = "#c62828"
fig.add_trace(go.Scatter(x=x_oval, y=y_oval, mode="lines", name="Rankine oval (ψ = 0)",
                         line=dict(color=oval_color, width=3)))
fig.add_trace(go.Scatter(x=x_oval, y=-y_oval, mode="lines", showlegend=False,
                         line=dict(color=oval_color, width=3)))
add_point(fig, -a, 0, "Source", "#1565c0")
add_point(fig, a, 0, "Sink", "#01bb1a")
fig.add_trace(go.Scatter(
    x=stagnation_x, y=[0, 0], mode="markers", name="Stagnation points",
    marker=dict(symbol="x", size=14, color="white", line=dict(color=oval_color, width=2)),
))
style_flow_figure(fig, "Step 2: Rankine oval and characteristic points")
show_plotly(fig)


### Step 3 — Add a sparse velocity-direction field

The arrows are normalized, so they show direction rather than velocity magnitude.

In [97]:
fig = go.Figure()
add_contours(fig, psi_plot, levels[0], levels[14], levels[1] - levels[0])
add_contours(fig, psi_plot, levels[15], levels[-1], levels[16] - levels[15])

oval_color = "#c62828"
fig.add_trace(go.Scatter(x=x_oval, y=y_oval, mode="lines", name="Rankine oval (ψ = 0)",
                         line=dict(color=oval_color, width=3)))
fig.add_trace(go.Scatter(x=x_oval, y=-y_oval, mode="lines", showlegend=False,
                         line=dict(color=oval_color, width=3)))

xq = np.linspace(-3.6, 3.6, 13)
yq = np.linspace(-2.5, 2.5, 7)
Xq, Yq = np.meshgrid(xq, yq)
d_source = (Xq + a)**2 + Yq**2
d_sink = (Xq - a)**2 + Yq**2
with np.errstate(divide="ignore", invalid="ignore"):
    Uq = U + m * (Xq + a) / d_source - m * (Xq - a) / d_sink
    Vq = m * Yq / d_source - m * Yq / d_sink
    speed_q = np.hypot(Uq, Vq)
    Uq, Vq = Uq / speed_q, Vq / speed_q
near_singularity = (d_source < 0.16) | (d_sink < 0.16)
Uq = np.ma.array(Uq, mask=near_singularity | ~np.isfinite(Uq))
Vq = np.ma.array(Vq, mask=near_singularity | ~np.isfinite(Vq))
add_direction_arrows(fig, Xq, Yq, Uq, Vq)

add_point(fig, -a, 0, "Source", "#1565c0")
add_point(fig, a, 0, "Sink", "#01bb1a")
fig.add_trace(go.Scatter(
    x=stagnation_x, y=[0, 0], mode="markers", name="Stagnation points",
    marker=dict(symbol="star", size=16, color="white", line=dict(color=oval_color, width=2)),
))
fig.add_annotation(x=-x_stag, y=0, text=f"<b>stagnation x = −{x_stag:.3f}</b>",
                   showarrow=True, ax=-80, ay=-45, arrowcolor="#9D0303", font=dict(color="#9D0303", size=14, family="Arial Black, Arial, sans-serif"))
fig.add_annotation(x=x_stag, y=0, text=f"<b>stagnation x = {x_stag:.3f}</b>",
                   showarrow=True, ax=80, ay=-45, arrowcolor="#9D0303", font=dict(color="#9D0303", size=14, family="Arial Black, Arial, sans-serif"))
style_flow_figure(fig, "Source–sink streamlines in a uniform flow with a = m = U = 1")
show_plotly(fig)


## Source–sink pair in an inclined uniform flow: $\alpha=30^\circ$

Finally, let the uniform flow make a counterclockwise angle $\alpha$ with the positive $x$ axis. Its velocity components are $U\cos\alpha$ and $U\sin\alpha$, so its streamfunction is

$$\psi_U=U(y\cos\alpha-x\sin\alpha).$$

Adding the source–sink pair gives

$$\boxed{\psi(x,y)=U(y\cos\alpha-x\sin\alpha)+m\left[\operatorname{atan2}(y,x+a)-\operatorname{atan2}(y,x-a)\right]}.$$

The corresponding velocity components are

$$\begin{aligned}
u&=U\cos\alpha+m\frac{x+a}{(x+a)^2+y^2}-m\frac{x-a}{(x-a)^2+y^2},\\[4pt]
v&=U\sin\alpha+m\frac{y}{(x+a)^2+y^2}-m\frac{y}{(x-a)^2+y^2}.
\end{aligned}$$


In [98]:
alpha_deg = 30.0
alpha = np.deg2rad(alpha_deg)

psi_alpha = (
    U * (Y * np.cos(alpha) - X * np.sin(alpha))
    + m * (theta_source - theta_sink)
)
psi_alpha_plot = np.ma.array(psi_alpha, mask=singularity_mask | branch_cut_mask)

with np.errstate(divide="ignore", invalid="ignore"):
    u_alpha = U * np.cos(alpha) + m * (X + a) / r_source_sq - m * (X - a) / r_sink_sq
    v_alpha = U * np.sin(alpha) + m * Y / r_source_sq - m * Y / r_sink_sq

### Stagnation points

Using the complex potential, the complex velocity is

$$\frac{dF}{dz}=Ue^{-i\alpha}-\frac{2am}{z^2-a^2}.$$

Setting it equal to zero gives

$$\boxed{z_s=\pm\sqrt{a^2+\frac{2am}{U}e^{i\alpha}}}.$$

Unlike the aligned-flow case, the two stagnation points generally have different streamfunction values. Consequently, there is no single closed Rankine oval passing through both of them; the two highlighted contours below are the stagnation separatrices.

In [99]:
z_stag_alpha = np.sqrt(a**2 + (2 * a * m / U) * np.exp(1j * alpha))
z_stagnation = np.array([z_stag_alpha, -z_stag_alpha])
x_stagnation_alpha = z_stagnation.real
y_stagnation_alpha = z_stagnation.imag

def streamfunction_alpha(x_value, y_value):
    return (
        U * (y_value * np.cos(alpha) - x_value * np.sin(alpha))
        + m * np.arctan2(y_value, x_value + a)
        - m * np.arctan2(y_value, x_value - a)
    )

psi_stagnation = np.array([
    streamfunction_alpha(x_value, y_value)
    for x_value, y_value in zip(x_stagnation_alpha, y_stagnation_alpha)
])

for i, (x_value, y_value, psi_value) in enumerate(
    zip(x_stagnation_alpha, y_stagnation_alpha, psi_stagnation), start=1
):
    print(f"z{i} = ({x_value:.4f}, {y_value:.4f}),  psi = {psi_value:.4f}")

z1 = (1.6795, 0.2977),  psi = -0.8842
z2 = (-1.6795, -0.2977),  psi = 0.8842


### Streamlines for $\alpha=30^\circ$

The thin blue curves are streamlines. The red and purple curves pass through different stagnation points and therefore represent different streamfunction values. The normalized arrows show the local flow direction.

In [100]:
fig = go.Figure()

levels_alpha = np.linspace(-4.0, 4.0, 37)
add_contours(fig, psi_alpha_plot, levels_alpha[0], levels_alpha[-1], levels_alpha[1] - levels_alpha[0])

separatrix_colors = ["#c62828", "#6a1b9a"]
for i, (psi_value, color) in enumerate(zip(psi_stagnation, separatrix_colors), start=1):
    add_contours(fig, psi_alpha_plot, psi_value, psi_value, 1.0, color=color, width=3,
                 name=f"z{i} dividing streamline (ψ = {psi_value:.3f})", showlegend=True)

xqa = np.linspace(-3.6, 3.6, 13)
yqa = np.linspace(-2.5, 2.5, 7)
Xqa, Yqa = np.meshgrid(xqa, yqa)
d_source_a = (Xqa + a)**2 + Yqa**2
d_sink_a = (Xqa - a)**2 + Yqa**2
with np.errstate(divide="ignore", invalid="ignore"):
    Uqa = U * np.cos(alpha) + m * (Xqa + a) / d_source_a - m * (Xqa - a) / d_sink_a
    Vqa = U * np.sin(alpha) + m * Yqa / d_source_a - m * Yqa / d_sink_a
    speed_qa = np.hypot(Uqa, Vqa)
    Uqa, Vqa = Uqa / speed_qa, Vqa / speed_qa
near_singularity_a = (d_source_a < 0.16) | (d_sink_a < 0.16)
Uqa = np.ma.array(Uqa, mask=near_singularity_a | ~np.isfinite(Uqa))
Vqa = np.ma.array(Vqa, mask=near_singularity_a | ~np.isfinite(Vqa))
add_direction_arrows(fig, Xqa, Yqa, Uqa, Vqa)

add_point(fig, -a, 0, "Source", "#1565c0")
add_point(fig, a, 0, "Sink", "#01bb1a")
for i, (x_value, y_value, color) in enumerate(
    zip(x_stagnation_alpha, y_stagnation_alpha, separatrix_colors), start=1
):
    fig.add_trace(go.Scatter(
        x=[x_value], y=[y_value], mode="markers", showlegend=False,
        marker=dict(symbol="star", size=16, color="white", line=dict(color=color, width=2)),
    ))
fig.add_annotation(x=-2.25, y=2.35, text="<b>uniform flow U, α = 30°</b>", showarrow=True,
                   ax=-65, ay=55, arrowcolor="#1565c0", font=dict(color="#1565c0", size=14, family="Arial Black, Arial, sans-serif"))
style_flow_figure(fig, "Source–sink streamlines with inclined uniform flow (α = 30°)")
show_plotly(fig)
